In [1]:
import pandas as pd
import numpy as np
import plotly.express as px

# importerer hele datasettet
stations_df_full = pd.read_csv("../raw_data/stations.csv")

# konverterer til riktig format og tidssone for å sortere stations_df kronologisk
# PS - vil endre dtype på timestamp til Europe/Oslo
stations_df_full["timestamp"] = pd.to_datetime(stations_df_full["timestamp"], utc=True).dt.tz_convert("Europe/Oslo")
stations_df_full = stations_df_full.sort_values(by="timestamp", ascending=True)

# bruker indeksering for å kun bruke treningsdata (første 70%) i analyse 
split_index = int(0.7*len(stations_df_full))
stations_df = stations_df_full.iloc[: split_index]

Gjør først analyse på all data

In [2]:
# første 5 radene
head = stations_df.head()
head

,station,longitude,latitude,timestamp,skipped_updates,free_bikes,free_spots
242648,Bontelabo 8,5.316471,60.402481,2024-04-10 23:45:34+02:00,0,7,0
280710,Jonsvollkvartalet,5.317308,60.392677,2024-04-10 23:45:34+02:00,0,3,16
207030,Hans Hauges gate,5.324748,60.401906,2024-04-10 23:45:34+02:00,0,0,13
136384,Nykirken,5.313495,60.396949,2024-04-10 23:45:34+02:00,0,16,0
178815,Florida Bybanestopp,5.332332,60.382255,2024-04-10 23:45:34+02:00,0,0,24


In [3]:
# siste 5 radene (i treningsdata)
tail = stations_df.tail()
tail

,station,longitude,latitude,timestamp,skipped_updates,free_bikes,free_spots
243659,Stenersen,5.324792,60.390174,2025-02-17 17:49:03+01:00,1,1,18
43125,Nedre Korskirkeallmenning,5.327050,60.394550,2025-02-17 17:49:03+01:00,0,2,23
243837,Verftet,5.307756,60.395877,2025-02-17 17:49:03+01:00,0,3,16
38793,Kronstad bybanestopp,5.349553,60.371787,2025-02-17 17:49:03+01:00,1,6,19
129295,Ole Vigs gate,5.321432,60.385923,2025-02-17 18:06:47+01:00,36,1,9


In [4]:
# data info (inkludert dtype)
info = stations_df.info()
info

<class 'pandas.core.frame.DataFrame'>
Index: 202764 entries, 242648 to 129295
Data columns (total 7 columns):
 #   Column           Non-Null Count   Dtype                      
---  ------           --------------   -----                      
 0   station          202764 non-null  object                     
 1   longitude        202764 non-null  float64                    
 2   latitude         202764 non-null  float64                    
 3   timestamp        202764 non-null  datetime64[ns, Europe/Oslo]
 4   skipped_updates  202764 non-null  int64                      
 5   free_bikes       202764 non-null  int64                      
 6   free_spots       202764 non-null  int64                      
dtypes: datetime64[ns, Europe/Oslo](1), float64(2), int64(3), object(1)
memory usage: 12.4+ MB


In [5]:
# data beskrivelse
description = stations_df.describe(include='all')
description

,station,longitude,latitude,timestamp,skipped_updates,free_bikes,free_spots
count,202764,202764.000000,202764.000000,202764,202764.000000,202764.000000,202764.000000
unique,129,NaN,NaN,NaN,NaN,NaN,NaN
top,Torgallmenningen,NaN,NaN,NaN,NaN,NaN,NaN
freq,4527,NaN,NaN,NaN,NaN,NaN,NaN
mean,NaN,5.326963,60.388404,2024-10-26 12:57:23.749289728+02:00,7.114749,6.619543,13.062353
min,NaN,5.273174,60.341031,2024-04-10 23:45:34+02:00,0.000000,0.000000,0.000000
25%,NaN,5.320002,60.382255,2024-09-19 07:35:53+02:00,0.000000,1.000000,7.000000
50%,NaN,5.325714,60.388910,2024-10-18 23:23:30+02:00,1.000000,4.000000,13.000000
75%,NaN,5.333327,60.394550,2024-11-26 16:24:41+01:00,5.000000,10.000000,18.000000
max,NaN,5.361202,60.423343,2025-02-17 18:06:47+01:00,1445.000000,37.000000,57.000000


In [6]:
# hvor lenge målingene har holdt på (i treningsdata)
min = stations_df["timestamp"].min()
max = stations_df["timestamp"].max()

print("Målinger startet", min, "og sluttet", max)

Målinger startet 2024-04-10 23:45:34+02:00 og sluttet 2025-02-17 18:06:47+01:00


In [7]:
# sjekk for manglende verdier (i treningsdata)
isna = stations_df.isna().sum()
isna

station            0
longitude          0
latitude           0
timestamp          0
skipped_updates    0
free_bikes         0
free_spots         0
dtype: int64

In [8]:
# sjekk for unike rader (i treningsdata)
nunique = stations_df.nunique()
nunique

station              129
longitude            131
latitude             131
timestamp          12806
skipped_updates      437
free_bikes            38
free_spots            58
dtype: int64

In [9]:
# antall målinger per stasjon (i treningsdata)
value_count = stations_df["station"].value_counts()
value_count

station
Torgallmenningen           4527
Nykirken                   4437
Møllendalsplass            4404
St. Jakobs Plass           4233
C. Sundts gate             3945
                           ... 
Tinghuset                    11
Folke Bernadottesvei 38       7
Dag Hammarskjöldsvei 73       7
Kronstad Almenning            1
Mindemyren Bybanestopp        1
Name: count, Length: 129, dtype: int64

In [10]:
# total kapasitet (i treningsdata)
capacity = (stations_df["free_bikes"] + stations_df["free_spots"]).describe()
capacity

count    202764.000000
mean         19.681896
std           6.674704
min           5.000000
25%          16.000000
50%          19.000000
75%          25.000000
max          57.000000
dtype: float64

In [11]:
# gjennomsnitt per stasjon (i treningsdata)
stats = stations_df.groupby("station").agg(["mean", "median", "std", "min", "max"])
round(stats,2)

longitude                         latitude         \
                                 mean median  std   min   max     mean median   
station                                                                         
AdO arena                        5.34   5.34  0.0  5.34  5.34    60.39  60.39   
Akvariet                         5.30   5.30  0.0  5.30  5.30    60.40  60.40   
Allehelgens plass                5.33   5.33  0.0  5.33  5.33    60.39  60.39   
Amalie Skrams vei Nord           5.32   5.32  0.0  5.32  5.32    60.41  60.41   
Amalie Skrams vei Sør            5.33   5.33  0.0  5.33  5.33    60.41  60.41   
...                               ...    ...  ...   ...   ...      ...    ...   
Welhavens gate 64                5.32   5.32  0.0  5.32  5.32    60.38  60.38   
Zander Kaaes gate                5.34   5.34  0.0  5.34  5.34    60.39  60.39   
Østre Murallmenningen nedre      5.32   5.32  0.0  5.32  5.32    60.40  60.40   
Østre Murallmenningen øvre       5.32   5.32  0.0  5.32  5.32    60.39  60.39   
Øvre Korskirkeallmenning         5.33   5.33  0.0  5.33  5.33    60.40  60.40   

                                                ... free_bikes               \
                             std    min    max  ...       mean median   std   
station                                         ...                           
AdO arena                    0.0  60.39  60.39  ...       7.60    6.0  5.60   
Akvariet                     0.0  60.40  60.40  ...       4.07    3.0  3.74   
Allehelgens plass            0.0  60.39  60.39  ...       9.26    7.0  7.86   
Amalie Skrams vei Nord       0.0  60.41  60.41  ...       3.72    3.0  3.20   
Amalie Skrams vei Sør        0.0  60.41  60.41  ...       8.75    9.0  6.75   
...                          ...    ...    ...  ...        ...    ...   ...   
Welhavens gate 64            0.0  60.38  60.38  ...       2.34    2.0  2.28   
Zander Kaaes gate            0.0  60.39  60.39  ...       2.88    2.0  2.60   
Østre Murallmenningen nedre  0.0  60.40  60.40  ...       7.24    6.0  6.08   
Østre Murallmenningen øvre   0.0  60.39  60.39  ...       6.30    5.0  5.76   
Øvre Korskirkeallmenning     0.0  60.40  60.40  ...       1.94    2.0  1.58   

                                    free_spots                       
                            min max       mean median   std min max  
station                                                              
AdO arena                     0  19      11.23   12.0  5.64   0  19  
Akvariet                      0  18      13.62   15.0  3.82   0  18  
Allehelgens plass             0  26      16.52   19.0  7.91   0  26  
Amalie Skrams vei Nord        0  13       9.17   10.0  3.22   0  13  
Amalie Skrams vei Sør         0  25      15.86   16.0  6.82   0  25  
...                          ..  ..        ...    ...   ...  ..  ..  
Welhavens gate 64             0  11      16.54   17.0  2.28   8  19  
Zander Kaaes gate             0  10       7.03    8.0  2.63   0  10  
Østre Murallmenningen nedre   0  19      11.39   13.0  6.05   0  19  
Østre Murallmenningen øvre    0  19      12.36   14.0  5.77   0  19  
Øvre Korskirkeallmenning      0   6      18.47   18.5  3.30  14  23  

[129 rows x 30 columns]

In [12]:
# sjekker etter outliers (i treningsdata)
outliers = stations_df.query("free_bikes < 0 or free_spots < 0")
stations_df["capacity"] = stations_df["free_bikes"] + stations_df["free_spots"]
outliers_capacity = stations_df.query("free_bikes > capacity or free_spots > capacity")

if (outliers.empty and outliers_capacity.empty):
    print("Ingen outliers i treningsdata")


Ingen outliers i treningsdata


C:\Users\Jon\AppData\Local\Temp\ipykernel_19080\1386165847.py:3: SettingWithCopyWarning: 
A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy
  stations_df["capacity"] = stations_df["free_bikes"] + stations_df["free_spots"]


In [13]:
# visualiserer totalt antall ledige sykler per stasjon
fig = px.histogram(stations_df, "station", "free_bikes")
fig.update_layout(title="antall ledige sykler per stasjon", xaxis_title="stasjon", yaxis_title="sum av ledige sykler",
                   font=dict(size=12), template="simple_white", showlegend=False)
fig.show()

c:\Users\Jon\OneDrive - University of Bergen\Emne\3. semester\INF161\envs\INF161\Lib\site-packages\kaleido\__init__.py:14: UserWarning:




This means that static image generation (e.g. `fig.write_image()`) will not work.

Please upgrade Plotly to version 6.1.1 or greater, or downgrade Kaleido to version 0.2.1.




In [14]:
# visualiserer korrelasjon mellom tid på året og ledige sykler via histogram
fig = px.histogram(stations_df, "timestamp", "free_bikes")
fig.update_layout(title="antall ledige sykler over tid (alle stasjoner)", yaxis_title = "sum av ledige sykler",
                  font=dict(size=14), template="simple_white", showlegend=False)
fig.show()

Gjør så analyse med kun data fra target_stations

In [15]:
# OpenAI's ChatGPT ble brukt til å formulere og/eller komme opp med ideer for deler av kode.
# Dette gjelder target_stations_df, der det blir brukt resampling ihht til LOCF-prinsippet.
# All kode som er hjulpet av AI er forstått i seg selv og ihht til resten av programmet.
# OpenAI - https://chatgpt.com - henta 09.09.25 

# velger ut target_stations for videre analyse
target_stations = np.array(["Møllendalsplass", "Torgallmenningen", "Grieghallen",
                            "Høyteknologisenteret", "Studentboligene", "Akvariet",
                            "Damsgårdsveien 71", "Dreggsallmenningen Sør", "Florida Bybanestopp"])

# omgjør til format med en stasjon per kolonne, og ledige sykler i rad for enkel analyse
filtered_stations = stations_df[stations_df["station"].isin(target_stations)]
filtered_stations = filtered_stations.set_index("timestamp").sort_index()

# runder opp klokkeslett i data til neste hele time ihht LOCF og sorterer
target_stations_analysis_df = filtered_stations.groupby("station")["free_bikes"].apply(lambda s: s.resample("1h").ffill()
                                        ).reset_index().pivot(index="timestamp", columns="station", values="free_bikes").sort_index()

target_stations_analysis_df.columns.name = None
target_stations_analysis_df = target_stations_analysis_df.reset_index()

target_stations_analysis_df.head()

,timestamp,Akvariet,Damsgårdsveien 71,Dreggsallmenningen Sør,Florida Bybanestopp,Grieghallen,Høyteknologisenteret,Møllendalsplass,Studentboligene,Torgallmenningen
0,2024-04-10 23:00:00+02:00,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
1,2024-04-11 00:00:00+02:00,0.0,12.0,12.0,0.0,14.0,0.0,4.0,15.0,15.0
2,2024-04-11 01:00:00+02:00,0.0,12.0,12.0,0.0,14.0,0.0,4.0,16.0,15.0
3,2024-04-11 02:00:00+02:00,0.0,12.0,12.0,0.0,14.0,0.0,4.0,16.0,15.0
4,2024-04-11 03:00:00+02:00,0.0,12.0,12.0,0.0,14.0,0.0,4.0,16.0,15.0


In [16]:
# bruker melt i pandas for å sjekke at omgjort format til videre bruk ser riktig ut, 
# men beholder target_stations_analysis_df for enklere skissering
target_stations_df = target_stations_analysis_df.melt(
    id_vars=["timestamp"],
    var_name="station",
    value_name="free_bikes"
)

target_stations_df.head()

,timestamp,station,free_bikes
0,2024-04-10 23:00:00+02:00,Akvariet,NaN
1,2024-04-11 00:00:00+02:00,Akvariet,0.0
2,2024-04-11 01:00:00+02:00,Akvariet,0.0
3,2024-04-11 02:00:00+02:00,Akvariet,0.0
4,2024-04-11 03:00:00+02:00,Akvariet,0.0


In [17]:
# visualiserer forskjellen mellom faktiske data og filtrert data med LOCF 
# før videre analyse, på Grieghallen stasjon via lineplot

# sorterer ut Grieghallen og sorterer ut ledige sykler
grieghallen = stations_df[stations_df["station"] == "Grieghallen"]
filled = target_stations_analysis_df[["timestamp", "Grieghallen"]].rename(columns={"Grieghallen": "free_bikes"})

# definerer faktisk måling mot antatt måling og sammenligner på en tilfeldig periode i data
grieghallen["type"] = "faktisk måling"
filled["type"] = "antatt (LOCF)"

comparison = pd.concat([grieghallen, filled])

start_date = "2024-09-08"
end_date = "2024-09-10"

comparison_period = comparison[
    (comparison["timestamp"] >= start_date) & 
    (comparison["timestamp"] <= end_date)
]

fig = px.line(comparison_period, "timestamp", "free_bikes", color="type")
fig.update_layout(title="faktisk vs antatt antall sykler ved Grieghallen",
                  yaxis_title= "antall sykler")
fig.show()

C:\Users\Jon\AppData\Local\Temp\ipykernel_19080\469483082.py:9: SettingWithCopyWarning:


A value is trying to be set on a copy of a slice from a DataFrame.
Try using .loc[row_indexer,col_indexer] = value instead

See the caveats in the documentation: https://pandas.pydata.org/pandas-docs/stable/user_guide/indexing.html#returning-a-view-versus-a-copy



In [18]:
# visualiserer antall ledige sykler per måling i target_stations via histogram
for col in target_stations_analysis_df.columns:
    if (col != "timestamp"):
        fig = px.histogram(target_stations_analysis_df, x=col)
        fig.update_layout(xaxis_title="ledige sykler", yaxis_title="antall målinger",
                          title=f"antall ledige sykler per måling på stasjon: {col}")
        fig.show()

In [19]:
# visualiserer ledige sykler over tid per stasjon via histogram
for col in target_stations_analysis_df.columns:
    if (col!= "timestamp"):
        fig = px.histogram(target_stations_analysis_df, "timestamp", col, nbins=1000)
        fig.update_layout(yaxis_title="ledige sykler",
                          title=f"antall ledige sykler over tid per stasjon: {col}")
        fig.show()

In [20]:
# visualiserer ledige sykler per time på døgnet per stasjon via boxplot
for col in target_stations_analysis_df.columns:
        if (col != "timestamp"):
            stations_hour = target_stations_analysis_df.copy()
            stations_hour["hour"] = stations_hour["timestamp"].dt.hour
            fig = px.box(stations_hour, "hour", col)
            fig.update_layout(title=f"fordeling av ledige sykler per time på stasjon: {col}",
                            xaxis_title="time på døgnet")
            fig.show()

In [21]:
# visualiserer ledige sykler per dag i uka per stasjon via boxplot
for col in target_stations_analysis_df.columns:
        if (col != "timestamp"):
            stations_day_of_week = target_stations_analysis_df.copy()
            stations_day_of_week["day_of_week"] = stations_day_of_week["timestamp"].dt.day_name()
            fig = px.box(stations_day_of_week, "day_of_week", col)
            fig.update_layout(title=f"fordeling av ledige sykler per dag i uka på stasjon: {col}",
                        xaxis_title="dag i uka")
            fig.show()